In [1]:
import os
import struct
def read_bmp_file(filename):
  if not os.path.exists(filename):
    print("Error: The file does not exist.")
    return None
  #endswith start reading from right to left or start from end.
  from PIL import Image
  img = Image.open(filename)
  img.save(filename)
  if not filename.lower().endswith(".bmp"):
    print("Error: The input file is not a bmp file")
    return None

  try:
     with open(filename,"rb") as f:  #opens a file safely for reading in binary mode and assigns it to a file object named f
       file_header_data = f.read(14)
       if(len(file_header_data)<14):
         print("the bmp file header is corrupt")
         return None

       filetype,filesize,reserved1,reserved2,pixeloffset = struct.unpack("<2sIHHI", file_header_data)
       print(f"DEBUG: File signature found is: {filetype}")
       if filetype != b"BM":   #b tells to treat this as a raw binary data not text data
       #I unsigned 4 bit integer and H unsigned 2 byte integer. i for 4 byte signed integer.
       #struct.unpack takes a binary string and converts it based on a specific format layout. here the specific format is 2sIHHI 2s means a special 2 byte integer.
       #< means little endian format
                print("Error: Invalid BMP file signature.")
                return None
       info_header_data = f.read(40)
       colortable=[]
       if(len(info_header_data)<40):
         print("the bmp info header is corrupt")
       headersize,width,height,planes,bitperpixel,compression,imagesize,xpixpermetre,ypixpermetre,totcolor,importantcolor = struct.unpack("<IiiHHIIiiII", info_header_data)
       height = abs(height)
       if bitperpixel==24:
        colortable = None
       elif bitperpixel==8:
        for i in range(256):
          blue, green, red, reserved = struct.unpack("<BBBB", f.read(4))
          colortable.append([blue, green, red, reserved])
       else:
        print("Invalid Bits per Pixel")
        return None
       if bitperpixel==8:
         bytesperpixel = bitperpixel // 8
         rowsize = 4*((width*bytesperpixel + 3)//4)
         padding = rowsize - (width*bytesperpixel)
         f.seek(pixeloffset)
         pixel_data = []
         for i in range(height):
             pos = list(f.read(min(width*bytesperpixel,rowsize)))
             for j in range(padding):
               pos.append(0)
             pixel_data.append(pos)

       elif bitperpixel==24:
         bytesperpixel = bitperpixel // 8
         f.seek(pixeloffset)
         pixel_data = []
         bils = 1
         rowsize = 4*((width*bytesperpixel + 3)//4)
         padding = rowsize - (width*bytesperpixel)
         for i in range(height):
           pos = []
           for j in range(width*bils):
             blue,green,red = struct.unpack("<BBB",f.read(3))
             pose = [blue,green,red]
             pos.append(pose)
           for j in range(padding):
             pos.append(0)
           pixel_data.append(pos)
       else:
        print("Invalid Bits per Pixel")
        return None


       bmp_dict = {
    "filetype": filetype,
    "filesize": filesize,
    "reserved1": reserved1,
    "reserved2": reserved2,
    "pixeloffset": pixeloffset,
    "headersize": headersize,
    "width": width,
    "height": height,
    "planes": planes,
    "bitperpixel": bitperpixel,
    "compression": compression,
    "imagesize": imagesize,
    "xpixpermetre": xpixpermetre,
    "ypixpermetre": ypixpermetre,
    "totcolor": totcolor,
    "colortable": colortable,
    "importantcolor": importantcolor,
    "pixel_data":pixel_data,
    "padding":padding
}

       return bmp_dict
  except Exception as e:
    print(f"unexpected file system error has occured : {e}")
    return None


In [2]:
def write_bmp_file(filename,bmp_dict):
  try:
    width = bmp_dict['width']
    height = bmp_dict['height']
    bitperpixel = bmp_dict['bitperpixel']
    if bitperpixel!=24 and bitperpixel!=8:
      print("Invalid Bits per Pixel")
      return None
    padding = bmp_dict['padding']
    colortable = bmp_dict['colortable']
    pixel_data = bmp_dict['pixel_data']

    file_header = struct.pack("<2sIHHI",b"BM",bmp_dict['filesize'],bmp_dict['reserved1'],bmp_dict['reserved2'],bmp_dict['pixeloffset'])
    info_header = struct.pack("<IiiHHIIiiII",bmp_dict['headersize'],bmp_dict["width"],bmp_dict["height"],bmp_dict["planes"],bmp_dict["bitperpixel"], bmp_dict["compression"],bmp_dict["imagesize"],bmp_dict["xpixpermetre"],bmp_dict["ypixpermetre"],bmp_dict["totcolor"],bmp_dict["importantcolor"])

    with open(filename, "wb") as f:
      f.write(file_header)
      f.write(info_header)
      if bitperpixel==8:
       for i in range(256):
         f.write(struct.pack("<BBBB",colortable[i][0],colortable[i][1],colortable[i][2],colortable[i][3]))
      if bitperpixel == 8:
        bytesperpixel = bitperpixel//8
        for i in range(height):
          for j in range(width+padding):
            f.write(struct.pack(
                                    "<B",
                                    pixel_data[i][j]
                                ))
      else:
        for i in range(height):
          for j in range(width):
            f.write(struct.pack("<BBB",pixel_data[i][j][0],pixel_data[i][j][1],pixel_data[i][j][2]))
          for k in range(padding):
            f.write(struct.pack("<B",0))
      print("BMP file successfully written:")
      print(filename)
  except Exception as e:
       print(f"Error while writing BMP file: {e}")

In [3]:
import copy
def channel_modulation(filename):
  bmp = read_bmp_file(filename)
  name = os.path.splitext(os.path.basename(filename))[0]


  if bmp['bitperpixel']!=24 and bmp['bitperpixel']!=8:
      print("Invalid Bits per Pixel")
      return None
  elif bmp['bitperpixel']==8:
    original_color = copy.deepcopy(bmp['colortable'])

    for k in range(3):
      colortable = copy.deepcopy(original_color)
      for j in range(256):
        colortable[j][k] = 0
      bmp['colortable'] = colortable
      write_bmp_file(f"/content/output_{name}_{k}.bmp",bmp)
  else:
    original_copy = copy.deepcopy(bmp['pixel_data'])
    for k in range(3):

     pixel_data = copy.deepcopy(original_copy)

     for i in range(bmp['height']):
      for j in range(bmp['width']):
        pixel_data[i][j][k] = 0
     bmp['pixel_data'] = pixel_data
     write_bmp_file(f"/content/output_{name}_{k}.bmp",bmp)


In [4]:
bmp = read_bmp_file('/content/pepper.bmp')
print("File Type:", bmp["filetype"])
print("File Size:", bmp["filesize"])
print("Reserved 1:", bmp["reserved1"])
print("Reserved 2:", bmp["reserved2"])
print("Pixel Data Offset:", bmp["pixeloffset"])
print("Header Size:", bmp["headersize"])
print("Image Width:", bmp["width"])
print("Image Height:", bmp["height"])
print("Number of Planes:", bmp["planes"])
print("Bits Per Pixel:", bmp["bitperpixel"])
print("Compression Type:", bmp["compression"])
print("Image Size:", bmp["imagesize"])
print("Horizontal Resolution:", bmp["xpixpermetre"])
print("Vertical Resolution:", bmp["ypixpermetre"])
print("Total Colors:", bmp["totcolor"])
print("Color Table:", bmp["colortable"])
print("Important Colors:", bmp["importantcolor"])
print("Pixel Data:", bmp["pixel_data"])
print("Padding Bytes:", bmp["padding"])
print("Number of rows:", len(bmp["pixel_data"]))
print("First row:", bmp["pixel_data"][1])
print("First pixel:", bmp["pixel_data"][1][1])

DEBUG: File signature found is: b'BM'
File Type: b'BM'
File Size: 786486
Reserved 1: 0
Reserved 2: 0
Pixel Data Offset: 54
Header Size: 40
Image Width: 512
Image Height: 512
Number of Planes: 1
Bits Per Pixel: 24
Compression Type: 0
Image Size: 786432
Horizontal Resolution: 3780
Vertical Resolution: 3780
Total Colors: 0
Color Table: None
Important Colors: 0
Pixel Data: [[[0, 0, 93], [36, 79, 119], [58, 135, 139], [57, 143, 136], [72, 164, 141], [59, 113, 136], [33, 76, 101], [48, 124, 128], [50, 133, 129], [55, 163, 165], [81, 173, 182], [75, 183, 188], [73, 172, 183], [69, 177, 182], [57, 180, 194], [63, 185, 195], [65, 199, 203], [69, 202, 198], [89, 205, 203], [81, 204, 198], [89, 205, 200], [101, 205, 200], [84, 200, 196], [97, 206, 199], [88, 206, 198], [83, 205, 200], [95, 206, 198], [76, 206, 200], [77, 202, 200], [75, 200, 193], [73, 207, 203], [76, 207, 198], [75, 209, 207], [75, 200, 202], [94, 208, 202], [76, 206, 201], [96, 206, 197], [76, 209, 197], [84, 206, 197], [97, 20

In [5]:
for i in range(bmp["height"]):
 print(f"Index: {i+1}")
 print("Width:", bmp["width"])
 print("Height:", bmp["height"])
 print("Bits:", bmp["bitperpixel"])
 print("Number of rows:", len(bmp["pixel_data"]))
 print("row:", bmp["pixel_data"][i])

Index: 1
Width: 512
Height: 512
Bits: 24
Number of rows: 512
row: [[0, 0, 93], [36, 79, 119], [58, 135, 139], [57, 143, 136], [72, 164, 141], [59, 113, 136], [33, 76, 101], [48, 124, 128], [50, 133, 129], [55, 163, 165], [81, 173, 182], [75, 183, 188], [73, 172, 183], [69, 177, 182], [57, 180, 194], [63, 185, 195], [65, 199, 203], [69, 202, 198], [89, 205, 203], [81, 204, 198], [89, 205, 200], [101, 205, 200], [84, 200, 196], [97, 206, 199], [88, 206, 198], [83, 205, 200], [95, 206, 198], [76, 206, 200], [77, 202, 200], [75, 200, 193], [73, 207, 203], [76, 207, 198], [75, 209, 207], [75, 200, 202], [94, 208, 202], [76, 206, 201], [96, 206, 197], [76, 209, 197], [84, 206, 197], [97, 208, 201], [103, 208, 198], [109, 213, 202], [122, 205, 200], [80, 208, 198], [108, 207, 197], [94, 207, 199], [85, 207, 201], [95, 204, 198], [82, 211, 202], [94, 205, 199], [97, 208, 201], [102, 211, 197], [106, 209, 200], [98, 207, 202], [107, 208, 193], [106, 209, 200], [91, 207, 197], [114, 210, 202], [

In [6]:
output_file = "/content/output_pepper.bmp"
write_bmp_file(output_file,bmp)

BMP file successfully written:
/content/output_pepper.bmp


In [7]:
channel_modulation('/content/pepper.bmp')

DEBUG: File signature found is: b'BM'
BMP file successfully written:
/content/output_pepper_0.bmp
BMP file successfully written:
/content/output_pepper_1.bmp
BMP file successfully written:
/content/output_pepper_2.bmp


In [8]:
bmp = read_bmp_file('/content/corn.bmp')
print("File Type:", bmp["filetype"])
print("File Size:", bmp["filesize"])
print("Reserved 1:", bmp["reserved1"])
print("Reserved 2:", bmp["reserved2"])
print("Pixel Data Offset:", bmp["pixeloffset"])
print("Header Size:", bmp["headersize"])
print("Image Width:", bmp["width"])
print("Image Height:", bmp["height"])
print("Number of Planes:", bmp["planes"])
print("Bits Per Pixel:", bmp["bitperpixel"])
print("Compression Type:", bmp["compression"])
print("Image Size:", bmp["imagesize"])
print("Horizontal Resolution:", bmp["xpixpermetre"])
print("Vertical Resolution:", bmp["ypixpermetre"])
print("Total Colors:", bmp["totcolor"])
print("Color Table:", bmp["colortable"])
print("Important Colors:", bmp["importantcolor"])
print("Pixel Data:", bmp["pixel_data"])
print("Padding Bytes:", bmp["padding"])
print("Number of rows:", len(bmp["pixel_data"]))
print("First row:", bmp["pixel_data"][1])
print("First pixel:", bmp["pixel_data"][1][1])

DEBUG: File signature found is: b'BM'
File Type: b'BM'
File Size: 130558
Reserved 1: 0
Reserved 2: 0
Pixel Data Offset: 1078
Header Size: 40
Image Width: 312
Image Height: 415
Number of Planes: 1
Bits Per Pixel: 8
Compression Type: 0
Image Size: 129480
Horizontal Resolution: 3780
Vertical Resolution: 3780
Total Colors: 256
Color Table: [[12, 5, 15, 0], [100, 93, 93, 0], [17, 2, 147, 0], [71, 169, 241, 0], [32, 111, 196, 0], [13, 2, 79, 0], [66, 43, 153, 0], [176, 169, 161, 0], [54, 40, 86, 0], [124, 98, 203, 0], [120, 107, 101, 0], [20, 4, 205, 0], [64, 39, 214, 0], [161, 205, 243, 0], [18, 66, 143, 0], [16, 6, 111, 0], [35, 30, 44, 0], [33, 97, 170, 0], [126, 97, 243, 0], [133, 170, 195, 0], [123, 106, 147, 0], [78, 118, 195, 0], [69, 71, 90, 0], [95, 67, 215, 0], [67, 72, 149, 0], [14, 49, 119, 0], [10, 6, 47, 0], [83, 99, 161, 0], [20, 5, 167, 0], [152, 132, 147, 0], [174, 237, 248, 0], [124, 202, 247, 0], [21, 5, 241, 0], [126, 145, 233, 0], [14, 33, 88, 0], [126, 137, 191, 0], [16

In [9]:
for i in range(bmp["height"]):
 print(f"Index: {i+1}")
 print("Width:", bmp["width"])
 print("Height:", bmp["height"])
 print("Bits:", bmp["bitperpixel"])
 print("Number of rows:", len(bmp["pixel_data"]))
 print("row:", bmp["pixel_data"][i])

Index: 1
Width: 312
Height: 415
Bits: 8
Number of rows: 415
row: [95, 38, 123, 45, 10, 80, 80, 97, 97, 10, 97, 97, 75, 97, 42, 22, 38, 85, 69, 118, 118, 30, 30, 108, 54, 108, 54, 108, 30, 13, 13, 13, 98, 19, 39, 88, 20, 70, 122, 101, 77, 101, 101, 101, 122, 101, 122, 101, 29, 80, 72, 89, 10, 80, 48, 48, 117, 117, 77, 117, 48, 117, 48, 10, 97, 97, 1, 82, 104, 44, 44, 86, 8, 72, 75, 22, 95, 89, 22, 38, 95, 38, 22, 22, 75, 97, 72, 22, 95, 22, 42, 22, 38, 22, 22, 22, 22, 22, 22, 22, 22, 22, 22, 42, 22, 22, 123, 88, 88, 107, 107, 68, 68, 68, 68, 3, 68, 68, 84, 68, 81, 21, 24, 102, 24, 83, 107, 105, 105, 96, 33, 33, 68, 68, 33, 68, 68, 18, 68, 68, 23, 81, 92, 85, 43, 24, 107, 33, 52, 31, 13, 74, 13, 74, 118, 52, 126, 126, 68, 84, 37, 25, 27, 107, 78, 19, 49, 19, 105, 19, 98, 49, 19, 49, 35, 78, 35, 35, 88, 88, 94, 21, 71, 69, 98, 13, 108, 108, 54, 108, 54, 54, 54, 54, 54, 54, 54, 54, 54, 108, 13, 52, 98, 21, 56, 107, 49, 36, 49, 36, 49, 33, 101, 101, 49, 36, 101, 101, 70, 49, 87, 82, 82, 48,

In [10]:
output_file = "/content/output_corn.bmp"
write_bmp_file(output_file,bmp)

BMP file successfully written:
/content/output_corn.bmp


In [11]:
channel_modulation('/content/corn.bmp')

DEBUG: File signature found is: b'BM'
BMP file successfully written:
/content/output_corn_0.bmp
BMP file successfully written:
/content/output_corn_1.bmp
BMP file successfully written:
/content/output_corn_2.bmp


In [12]:
bmp = read_bmp_file('/content/cameraman.bmp')
print("File Type:", bmp["filetype"])
print("File Size:", bmp["filesize"])
print("Reserved 1:", bmp["reserved1"])
print("Reserved 2:", bmp["reserved2"])
print("Pixel Data Offset:", bmp["pixeloffset"])
print("Header Size:", bmp["headersize"])
print("Image Width:", bmp["width"])
print("Image Height:", bmp["height"])
print("Number of Planes:", bmp["planes"])
print("Bits Per Pixel:", bmp["bitperpixel"])
print("Compression Type:", bmp["compression"])
print("Image Size:", bmp["imagesize"])
print("Horizontal Resolution:", bmp["xpixpermetre"])
print("Vertical Resolution:", bmp["ypixpermetre"])
print("Total Colors:", bmp["totcolor"])
print("Color Table:", bmp["colortable"])
print("Important Colors:", bmp["importantcolor"])
print("Pixel Data:", bmp["pixel_data"])
print("Padding Bytes:", bmp["padding"])
print("Number of rows:", len(bmp["pixel_data"]))
print("First row:", bmp["pixel_data"][1])
print("First pixel:", bmp["pixel_data"][1][1])

DEBUG: File signature found is: b'BM'
File Type: b'BM'
File Size: 66614
Reserved 1: 0
Reserved 2: 0
Pixel Data Offset: 1078
Header Size: 40
Image Width: 256
Image Height: 256
Number of Planes: 1
Bits Per Pixel: 8
Compression Type: 0
Image Size: 65536
Horizontal Resolution: 3780
Vertical Resolution: 3780
Total Colors: 256
Color Table: [[0, 0, 0, 0], [1, 1, 1, 0], [2, 2, 2, 0], [3, 3, 3, 0], [4, 4, 4, 0], [5, 5, 5, 0], [6, 6, 6, 0], [7, 7, 7, 0], [8, 8, 8, 0], [9, 9, 9, 0], [10, 10, 10, 0], [11, 11, 11, 0], [12, 12, 12, 0], [13, 13, 13, 0], [14, 14, 14, 0], [15, 15, 15, 0], [16, 16, 16, 0], [17, 17, 17, 0], [18, 18, 18, 0], [19, 19, 19, 0], [20, 20, 20, 0], [21, 21, 21, 0], [22, 22, 22, 0], [23, 23, 23, 0], [24, 24, 24, 0], [25, 25, 25, 0], [26, 26, 26, 0], [27, 27, 27, 0], [28, 28, 28, 0], [29, 29, 29, 0], [30, 30, 30, 0], [31, 31, 31, 0], [32, 32, 32, 0], [33, 33, 33, 0], [34, 34, 34, 0], [35, 35, 35, 0], [36, 36, 36, 0], [37, 37, 37, 0], [38, 38, 38, 0], [39, 39, 39, 0], [40, 40, 40, 

In [13]:
for i in range(bmp["height"]):
 print(f"Index: {i+1}")
 print("Width:", bmp["width"])
 print("Height:", bmp["height"])
 print("Bits:", bmp["bitperpixel"])
 print("Number of rows:", len(bmp["pixel_data"]))
 print("row:", bmp["pixel_data"][i])

Index: 1
Width: 256
Height: 256
Bits: 8
Number of rows: 256
row: [233, 211, 216, 192, 188, 211, 192, 226, 203, 174, 205, 191, 197, 226, 205, 202, 185, 217, 199, 197, 211, 211, 214, 217, 216, 197, 173, 180, 211, 185, 81, 100, 124, 112, 137, 136, 142, 135, 128, 111, 89, 80, 82, 104, 122, 125, 114, 137, 143, 135, 118, 183, 208, 198, 183, 178, 188, 182, 184, 191, 178, 225, 162, 54, 53, 52, 51, 66, 92, 113, 99, 125, 145, 156, 156, 165, 159, 156, 161, 170, 151, 77, 60, 130, 198, 193, 215, 200, 219, 199, 189, 182, 211, 211, 195, 205, 196, 200, 218, 200, 156, 115, 145, 133, 208, 220, 246, 252, 255, 243, 182, 213, 191, 208, 208, 211, 240, 192, 190, 214, 212, 168, 179, 185, 186, 217, 205, 209, 192, 217, 203, 205, 215, 212, 228, 185, 187, 217, 181, 218, 204, 198, 187, 191, 189, 177, 193, 210, 170, 160, 200, 179, 173, 184, 181, 182, 182, 178, 186, 198, 184, 189, 212, 180, 226, 205, 170, 177, 202, 202, 188, 203, 164, 173, 197, 225, 194, 176, 206, 229, 194, 225, 181, 229, 207, 198, 204, 195, 178, 18

In [14]:
output_file = "/content/output_cameraman.bmp"
write_bmp_file(output_file,bmp)

BMP file successfully written:
/content/output_cameraman.bmp


In [15]:
channel_modulation('/content/cameraman.bmp')

DEBUG: File signature found is: b'BM'
BMP file successfully written:
/content/output_cameraman_0.bmp
BMP file successfully written:
/content/output_cameraman_1.bmp
BMP file successfully written:
/content/output_cameraman_2.bmp
